# Study Jam #5 — Build Your First AI-Powered App with Gemini API

Notebook hands-on ini memandu kamu membuat mini prototype AI app dengan Gemini API.

## Target akhir

Kita akan membuat beberapa demo kecil:

1. First Gemini API call
2. Prompting demo
3. Interactive input seperti chatbot sederhana
4. Structured output dengan JSON/schema
5. AI Study Assistant
6. Image Analyzer
7. Audio Analyzer
8. Text-to-Audio output dengan TTS

> Fokus notebook ini bukan deployment, melainkan memahami alur dasar aplikasi AI:
>
> **User input → Gemini API → response → parsing → output UI**

## 0. Aturan sebelum mulai

Sebelum menjalankan notebook ini, pastikan kamu sudah punya API key Gemini.

### Cara mendapatkan API key

1. Buka **Google AI Studio**
2. Masuk ke menu **API Keys**
3. Klik **Create API key**
4. Copy API key
5. Di Google Colab, buka sidebar kiri bagian **Secrets / Rahasia**
6. Tambahkan secret baru:

```text
Name  : GEMINI_API_KEY
Value : API key kamu
```

7. Aktifkan toggle akses secret untuk notebook ini

### Penting

Jangan pernah menulis API key langsung di kode seperti ini:

```python
api_key = "AIzaSy..."
```

API key harus disimpan di Colab Secrets agar lebih aman.

# Part 1 — Setup Gemini API

## 1. Install Gemini SDK

Jalankan cell ini sekali di awal.

Kita tidak memakai `-U` agar package bawaan Colab tidak ikut ter-upgrade terlalu agresif.

In [ ]:
!pip install -q "google-genai>=1.66.0,<2.0.0"

## 2. Import library

Penjelasan singkat:

- `genai`: library utama untuk memanggil Gemini API
- `BaseModel`, `Field`, `ValidationError`: dipakai untuk structured output/schema
- `display`, `Markdown`, `Audio`: agar output di Colab tampil rapi
- `getpass`: fallback untuk input API key manual jika Colab Secrets belum terbaca

In [ ]:
import os
import json
import wave
from getpass import getpass
from typing import List, Literal

from google import genai
from google.genai import types

from pydantic import BaseModel, Field, ValidationError

from IPython.display import display, Markdown, Audio, clear_output

## 3. Ambil API key dari Colab Secrets

Cell ini akan mencoba mengambil API key dari Colab Secrets.

Kalau secret tidak ditemukan, notebook akan meminta kamu memasukkan API key manual dengan `getpass()`.

In [ ]:
try:
    from google.colab import userdata
    api_key = userdata.get("GEMINI_API_KEY")
except Exception:
    api_key = None

if not api_key:
    api_key = getpass("Masukkan GEMINI_API_KEY: ")

print("API key berhasil terbaca:", api_key is not None)

API key berhasil terbaca: True


## 4. Buat Gemini client

`client` adalah object yang dipakai Python untuk berkomunikasi dengan Gemini API.

Untuk demo utama, kita pakai `gemini-3.5-flash` karena cukup cepat dan cocok untuk prototype.

In [ ]:
client = genai.Client(api_key=api_key)

MODEL_NAME = "gemini-3.5-flash"

print("Gemini client sudah siap.")
print("Model utama:", MODEL_NAME)

Gemini client sudah siap.
Model utama: gemini-3.5-flash


# Part 2 — First Gemini API Call

## 5. First request

Di Gemini API, request paling sederhana memakai:

```python
client.models.generate_content(...)
```

Parameter penting:

- `model`: nama model yang dipakai
- `contents`: input/prompt yang dikirim ke model
- `response.text`: jawaban teks dari model

In [ ]:
response = client.models.generate_content(
    model=MODEL_NAME,
    contents="Jelaskan apa itu API dalam bahasa Indonesia yang sederhana."
)

print(response.text)
display(Markdown(response.text))

**API** adalah singkatan dari *Application Programming Interface*. Tapi, mari kita lupakan istilah rumit itu dan gunakan analogi yang mudah dipahami.

Bayangkan **API sebagai "Pelayan" di sebuah restoran**.

Di dalam restoran tersebut:
1. **Kamu (sebagai Pelanggan)** adalah sebuah aplikasi di HP-mu (misalnya: aplikasi cuaca).
2. **Dapur Restoran** adalah server atau database yang punya informasi yang kamu butuhkan (misalnya: data cuaca dari BMKG).
3. **Pelayan** adalah **API**-nya.

Ketika kamu ingin tahu suhu hari ini:
* Kamu tidak langsung masuk ke dapur restoran untuk melihat makanan. 
* Kamu memesan lewat **Pelayan (API)**.
* Pelayan pergi ke **Dapur (Server)**, mengambilkan informasi suhu tersebut, lalu mengantarkannya kembali ke mejamu **(Aplikasi HP-mu)**.

---

### Contoh Nyata dalam Kehidupan Sehari-hari

Tanpa sadar, kita menggunakan API setiap hari:

1. **Log In Menggunakan Akun Google/Facebook:** 
   Saat kamu ingin masuk ke aplikasi baru (seperti Spotify atau game), sering

**API** adalah singkatan dari *Application Programming Interface*. Tapi, mari kita lupakan istilah rumit itu dan gunakan analogi yang mudah dipahami.

Bayangkan **API sebagai "Pelayan" di sebuah restoran**.

Di dalam restoran tersebut:
1. **Kamu (sebagai Pelanggan)** adalah sebuah aplikasi di HP-mu (misalnya: aplikasi cuaca).
2. **Dapur Restoran** adalah server atau database yang punya informasi yang kamu butuhkan (misalnya: data cuaca dari BMKG).
3. **Pelayan** adalah **API**-nya.

Ketika kamu ingin tahu suhu hari ini:
* Kamu tidak langsung masuk ke dapur restoran untuk melihat makanan. 
* Kamu memesan lewat **Pelayan (API)**.
* Pelayan pergi ke **Dapur (Server)**, mengambilkan informasi suhu tersebut, lalu mengantarkannya kembali ke mejamu **(Aplikasi HP-mu)**.

---

### Contoh Nyata dalam Kehidupan Sehari-hari

Tanpa sadar, kita menggunakan API setiap hari:

1. **Log In Menggunakan Akun Google/Facebook:** 
   Saat kamu ingin masuk ke aplikasi baru (seperti Spotify atau game), sering kali ada pilihan "Masuk dengan Google". Aplikasi tersebut menggunakan API Google untuk memverifikasi bahwa itu benar-benar kamu, tanpa Google harus memberikan kata sandimu ke aplikasi tersebut.
2. **Peta di Aplikasi Gojek atau Grab:**
   Gojek tidak membuat peta dunia sendiri dari nol. Mereka menggunakan **API Google Maps** untuk menampilkan peta dan rute jalan di aplikasi mereka.
3. **Pembayaran Digital (QRIS/Transfer Bank):**
   Saat kamu belanja online dan membayar lewat M-Banking atau e-wallet, toko online tersebut menggunakan API bank untuk memeriksa apakah pembayaranmu sudah masuk atau belum.

---

### Mengapa API itu Penting?

* **Menghemat Waktu:** Developer (pembuat aplikasi) tidak perlu membuat semuanya dari nol. Jika ingin membuat aplikasi ojek online, mereka tidak perlu bikin satelit dan peta sendiri, cukup pakai API Google Maps.
* **Keamanan:** API bertindak sebagai penjaga gerbang. Aplikasi luar hanya bisa meminta data yang diizinkan saja, tanpa bisa mengacak-acak sistem utama.
* **Membuat Aplikasi Saling Terhubung:** Tanpa API, aplikasi di HP-mu akan bekerja sendiri-sendiri dan tidak bisa saling bertukar informasi.

**Kesimpulan sederhana:** API adalah **jembatan penyeberangan** yang menghubungkan satu aplikasi dengan aplikasi lainnya agar mereka bisa saling mengobrol dan bekerja sama.

## 6. Helper function `ask_gemini`

Supaya kita tidak menulis kode panjang berulang-ulang, kita buat function.

Parameter:

- `prompt`: instruksi/pertanyaan untuk Gemini
- `temperature`: mengatur kreativitas jawaban
  - rendah: lebih stabil dan terarah
  - tinggi: lebih bebas dan kreatif

In [ ]:
def ask_gemini(prompt, temperature=0.3):
    response = client.models.generate_content(
        model=MODEL_NAME,
        contents=prompt,
        config={
            "temperature": temperature
        }
    )
    return response.text

temperature rendah  → jawaban lebih stabil, serius, konsisten

temperature tinggi  → jawaban lebih kreatif, variatif, kadang lebih tidak terduga

## 7. Test helper function

In [ ]:
answer = ask_gemini("Jelaskan neural network dalam 3 kalimat.")
display(Markdown(answer))

**Neural network** adalah model komputasi yang dirancang meniru cara kerja jaringan saraf otak manusia dalam memproses informasi. Sistem ini terdiri dari lapisan-lapisan "neuron" buatan yang saling terhubung untuk menganalisis data dan mengenali pola yang rumit. Melalui proses pembelajaran dari data tersebut, neural network mampu membuat prediksi akurat dan mengambil keputusan secara otomatis.

# Part 3 — Prompting Basics

## 8. Konsep prompting

Prompt bukan cuma pertanyaan. Prompt adalah instruksi kerja untuk model.

Prompt yang baik biasanya punya:

1. **Role**: model berperan sebagai apa
2. **Task**: model harus mengerjakan apa
3. **Context**: konteks atau audiensnya siapa
4. **Input**: data yang harus diproses
5. **Constraint**: batasan jawaban
6. **Output format**: bentuk jawaban yang diinginkan

## 9. Bad prompt vs better prompt

Bad prompt bukan berarti hasilnya selalu jelek. Model modern tetap bisa memberi jawaban bagus.

Tapi better prompt biasanya membuat output lebih:

- terarah
- rapi
- sesuai kebutuhan
- mudah dipakai aplikasi

In [ ]:
bad_prompt = '''
Bantu aku belajar materi ini:
Neural network adalah model machine learning yang terdiri dari neuron, layer, weight, bias, dan activation function.
'''

better_prompt = '''
Kamu adalah AI Study Assistant untuk mahasiswa pemula.

Tugas:
Ubah materi berikut menjadi bahan belajar yang rapi.

Materi:
Neural network adalah model machine learning yang terdiri dari neuron, layer, weight, bias, dan activation function.

Aturan:
- Gunakan bahasa Indonesia
- Langsung ke inti, tanpa sapaan pembuka
- Maksimal 5 poin penting
- Buat ringkasan singkat
- Buat 3 pertanyaan quiz
- Sertakan jawaban quiz
- Jangan menambahkan topik di luar materi

Format:
Ringkasan:
Poin Penting:
Quiz:
Jawaban:
'''

In [ ]:
bad_answer = ask_gemini(bad_prompt, temperature=0.7)
better_answer = ask_gemini(better_prompt, temperature=0.2)

display(Markdown("## Hasil Bad Prompt"))
display(Markdown(bad_answer))

display(Markdown("---"))

display(Markdown("## Hasil Better Prompt"))
display(Markdown(better_answer))

## Hasil Bad Prompt

Tentu, mari kita pelajari konsep **Neural Network (Jaringan Saraf Tiruan)** dengan cara yang paling mudah dipahami. 

Kita akan gunakan analogi sederhana: **"Bagaimana otak kita memutuskan apakah akan membeli sebuah handphone baru atau tidak."**

Mari kita bedah satu per satu komponennya!

---

### 1. Neuron (Node/Simpul)
Neuron adalah **unit terkecil** pemroses informasi. Di dalam program, neuron sebenarnya hanyalah sebuah wadah yang menyimpan angka.

*   **Analogi:** Bayangkan neuron seperti "sel otak" atau "asisten pengambil keputusan".
*   **Tugasnya:** Menerima informasi, memprosesnya, lalu meneruskan hasilnya ke neuron berikutnya.

---

### 2. Layer (Lapisan)
Neuron-neuron tidak bekerja sendirian, mereka dikelompokkan dalam beberapa **Layer (Lapisan)**. Umumnya ada 3 jenis layer:

1.  **Input Layer:** Tempat masuknya data mentah.
    *   *Contoh HP:* Input 1 (Harganya murah?), Input 2 (Kameranya bagus?), Input 3 (Baterainya awet?).
2.  **Hidden Layer (Lapisan Tersembunyi):** Tempat terjadinya "proses berpikir" yang rumit. Di sinilah komputer mencari pola-pola tersembunyi. (Bisa terdiri dari satu atau banyak layer).
3.  **Output Layer:** Hasil keputusan akhir.
    *   *Contoh HP:* Keputusannya cuma dua: "Beli" (1) atau "Tidak Beli" (0).

---

### 3. Weight (Bobot - $W$)
Tidak semua informasi itu sama pentingnya, bukan? Di sinilah peran **Weight (Bobot)**. Weight menentukan seberapa penting suatu input bagi keputusan kita.

*   **Analogi:** Seberapa sensitif kamu terhadap suatu fitur.
*   **Contoh:** 
    *   Jika kamu seorang fotografer, kamu akan memberikan **Weight yang besar (misal: 0.9)** pada input "Kamera Bagus".
    *   Jika kamu jarang keluar rumah, kamu akan memberikan **Weight yang kecil (misal: 0.1)** pada input "Baterai Awet".
*   **Rumus Matematis:** Input akan dikalikan dengan Weight ($Input \times Weight$).

---

### 4. Bias ($b$)
**Bias** adalah kecenderungan atau "sifat bawaan" sebelum mempertimbangkan data apa pun. 

*   **Analogi:** Bias adalah tingkat kepuasan atau "keremahan" dompetmu saat ini.
    *   Jika kamu sedang punya banyak uang, kamu punya **Bias positif yang besar**. Tanpa melihat spesifikasi HP pun, bawaannya ingin beli saja.
    *   Jika kamu sedang hemat, kamu punya **Bias negatif**. Sangat sulit meyakinkanmu untuk membeli HP tersebut.
*   **Rumus Sementara:** $(Input \times Weight) + Bias$

---

### 5. Activation Function (Fungsi Aktivasi)
Setelah kita mengalikan Input dengan Weight dan ditambah Bias, kita mendapatkan sebuah angka. Masalahnya, angka ini bisa berapa saja (misal: -150, 0.5, atau 2300). 

**Activation Function** bertugas mengubah angka acak tersebut menjadi format yang masuk akal (misalnya antara 0 sampai 1, atau memutuskan apakah neuron tersebut harus "aktif" atau "mati").

*   **Analogi:** Tombol saklar lampu. Saklar hanya punya dua kondisi: ON (Aktif) atau OFF (Mati). Fungsi aktivasi memutuskan apakah informasi ini cukup penting untuk diteruskan ke neuron berikutnya.
*   **Jenis yang populer:**
    *   **ReLU:** Jika hasilnya negatif, ubah jadi 0. Jika positif, biarkan apa adanya.
    *   **Sigmoid:** Mengubah angka berapa pun menjadi di antara 0 dan 1 (sangat cocok untuk menentukan probabilitas/persentase).

---

### Mari Kita Simulasikan Cara Kerjanya!

Bayangkan kita ingin menentukan apakah kamu akan **Beli HP Baru** ($Y$).

1.  **Input ($X$):**
    *   $X_1$ (Harganya Murah) = **1** (Ya, murah)
    *   $X_2$ (Kameranya Bagus) = **0** (Tidak bagus)
2.  **Weight ($W$):**
    *   $W_1$ (Pentingnya harga murah bagi kamu) = **4** (Sangat penting)
    *   $W_2$ (Pentingnya kamera bagi kamu) = **1** (Tidak terlalu penting)
3.  **Bias ($b$):**
    *   $b$ (Keinginan dasar kamu belanja) = **-2** (Sedang hemat)

**Langkah 1: Hitung total nilai (Penjumlahan Berbobot)**
$$\text{Total} = (X_1 \times W_1) + (X_2 \times W_2) + b$$
$$\text{Total} = (1 \times 4) + (0 \times 1) + (-2)$$
$$\text{Total} = 4 + 0 - 2 = \mathbf{2}$$

**Langkah 2: Masukkan ke Fungsi Aktivasi (Misal kita pakai aturan sederhana: jika $> 0$ maka "Beli", jika $\le 0$ maka "Tidak Beli")**
*   Karena hasil kita adalah **2** (lebih besar dari 0), maka fungsi aktivasi akan menghasilkan keputusan: **BELI!**

---

### Kuis Singkat untuk Menguji Pemahamanmu:
Jika sekarang kamu sedang **sangat hemat** sehingga nilai **Bias ($b$) berubah menjadi -5**, dengan input dan weight yang sama seperti di atas, **apakah kamu akan tetap membeli HP tersebut?** Coba hitung!

---

## Hasil Better Prompt

Ringkasan:
Neural network adalah sebuah model machine learning yang dibangun oleh beberapa komponen kunci, yaitu neuron, layer, weight, bias, dan activation function.

Poin Penting:
1. Neural network merupakan salah satu jenis model dalam machine learning.
2. Model ini terdiri dari elemen pemroses informasi yang disebut neuron.
3. Neuron-neuron di dalam model ini terstruktur dan diorganisasikan dalam beberapa layer (lapisan).
4. Model ini menggunakan weight (bobot) dan bias dalam strukturnya.
5. Activation function (fungsi aktivasi) merupakan komponen penting yang ada di dalam neural network.

Quiz:
1. Apa definisi dari neural network berdasarkan materi?
2. Sebutkan 5 komponen yang menyusun sebuah neural network!
3. Apakah activation function merupakan bagian dari neural network?

Jawaban:
1. Neural network adalah model machine learning.
2. Neuron, layer, weight, bias, dan activation function.
3. Ya, activation function adalah salah satu komponen penyusun neural network.

## 10. Interactive input: terasa seperti chatbot

Sebelum masuk structured output/schema, kita coba dulu membuat input onsite.

Ini membuat flow API terasa lebih nyata:

**User mengetik → Gemini menjawab → output tampil**

In [ ]:
user_question = input("Tulis pertanyaan kamu: ")

answer = ask_gemini(user_question)

display(Markdown("## Jawaban Gemini"))
display(Markdown(answer))

Tulis pertanyaan kamu: Item di Mobile Legends untuk mengcounter Healing


## Jawaban Gemini

Di Mobile Legends, item untuk meng-counter hero yang memiliki *healing* tinggi, *lifesteal*, *spell vamp*, atau *shield* tebal disebut sebagai item **Anti-Heal** (memiliki efek pasif **Life Drain**). 

Efek dari item-item ini adalah **mengurangi efek Regen HP, Lifesteal, Spell Vamp, dan Shield musuh sebesar 50%**.

Berikut adalah 3 item utama untuk meng-counter healing, disesuaikan dengan role hero yang kamu gunakan:

---

### 1. Sea Halberd (Untuk Hero Physical Damage)
Item ini sangat cocok untuk hero **Marksman, Fighter, atau Assassin** yang mengandalkan serangan fisik.

*   **Atribut:** +80 Physical Attack, +25% Attack Speed.
*   **Pasif Unik - Life Drain:** Memberikan damage ke target akan mengurangi efek Shield dan HP Regen mereka sebesar 50% selama 3 detik.
*   **Pasif Unik - Punish:** Meningkatkan damage sebesar 8% terhadap hero lawan yang memiliki HP tambahan lebih tinggi dari kamu (sangat bagus untuk melawan Tank/Fighter tebal).

### 2. Glowing Wand (Untuk Hero Magic Damage)
*Catatan: Pada update terbaru, item anti-heal untuk Mage yang dulunya bernama **Necklace of Durance (NoD)** kini telah dihapus dan efek anti-healnya digabungkan ke dalam **Glowing Wand**.*

Item ini wajib dibeli oleh **Mage atau Support** yang memberikan damage sihir.

*   **Atribut:** +75 Magic Power, +400 HP, +5% Movement Speed.
*   **Pasif Unik - Life Drain:** Memberikan Magic Damage ke target akan mengurangi efek Shield dan HP Regen mereka sebesar 50% selama 3 detik.
*   **Pasif Unik - Scorch:** Memberikan efek terbakar (burn) ke target setara dengan % HP mereka saat ini sebagai Magic Damage per detik.

### 3. Dominance Ice (Untuk Hero Tank / Fighter / Roamer)
Item pertahanan (defense) terbaik untuk meng-counter healing. Sangat cocok untuk **Tank, Fighter, atau Roamer** yang bertarung di garis depan (jarak dekat).

*   **Atribut:** +500 Mana, +70 Physical Defense, +4% Movement Speed.
*   **Pasif Unik - Life Drain:** Mengurangi Shield dan HP Regen hero lawan di sekitar (area) sebesar 50%.
*   **Pasif Unik - Arctic Cold:** Mengurangi Attack Speed hero lawan di sekitar sebesar 30%.

---

### Kapan Harus Membeli Item Anti-Heal?
Kamu wajib membeli salah satu dari item di atas jika musuh menggunakan hero-hero berikut:
*   **Healer murni:** Estes, Angela, Rafaela, Floryn, Minotaur.
*   **Hero dengan Lifesteal/Spell Vamp tinggi:** Ruby, Yu Zhong, Alucard, Alpha, Alice, Balmond, Thamuz.
*   **Hero dengan Shield tebal:** Esmeralda, Uranus, Harith, Freya.

### Tips Tambahan:
*   **Efek Anti-Heal tidak bisa di-stack.** Jika kamu memukul musuh menggunakan *Sea Halberd* dan temanmu menggunakan *Dominance Ice*, pengurangan heal tetap 50% (tidak menjadi 100%).
*   Meskipun tidak menumpuk, sangat disarankan minimal ada **2 orang** di tim yang membeli anti-heal (misalnya Roamer membeli *Dominance Ice* dan Mage membeli *Glowing Wand*) agar efek anti-heal bisa terus aktif selama war.

## 11. Chatbot loop sederhana

Cell ini membuat percakapan berulang.

Untuk berhenti, ketik salah satu dari:

```text
exit
quit
stop
keluar
```

Catatan: ini belum chatbot full dengan memory. Ini hanya interaksi berulang sederhana.

In [ ]:
while True:
    user_question = input("Kamu: ")

    if user_question.lower() in ["exit", "quit", "stop", "keluar"]:
        print("Chat selesai.")
        break

    answer = ask_gemini(user_question)

    display(Markdown("### Gemini"))
    display(Markdown(answer))

Kamu: Say hi to me


### Gemini

Hi there! How can I help you today?

Kamu: I just did my final exam


### Gemini

Congratulations! That is a huge milestone and a massive weight off your shoulders. 🎉

How are you feeling right now? Are you in "celebration mode," "nap mode," or just relieved that it's finally over? 

What subject was it?

Kamu: what i just finished?


### Gemini

Since we just started this chat, I don't have any context about what you were doing! 

Could you tell me what you were working on, or are you referring to a previous conversation we had? Let me know and I'll be happy to help you pick up where you left off!

Kamu: exit
Chat selesai.


## 12. Optional: chatbot dengan riwayat sederhana

Versi ini menyimpan riwayat percakapan dalam list.

Dengan begitu, pertanyaan berikutnya bisa mempertimbangkan percakapan sebelumnya.

In [ ]:
chat_history = []

def simple_chatbot(user_input):
    chat_history.append(f"User: {user_input}")

    prompt = f'''
Kamu adalah chatbot AI yang membantu peserta Study Jam.

Riwayat percakapan:
{chr(10).join(chat_history)}

Jawab pertanyaan terakhir user dengan bahasa Indonesia yang jelas.
'''

    answer = ask_gemini(prompt, temperature=0.3)

    chat_history.append(f"Gemini: {answer}")

    return answer

In [ ]:
while True:
    user_input = input("Kamu: ")

    if user_input.lower() in ["exit", "quit", "stop", "keluar"]:
        print("Chat selesai.")
        break

    answer = simple_chatbot(user_input)

    display(Markdown("### Gemini"))
    display(Markdown(answer))

Kamu: i just finish my final exam


### Gemini

Wah, selamat ya atas selesainya ujian akhirmu! 🎉 

Pasti rasanya sangat lega setelah berjuang keras mempersiapkannya. Sekarang waktunya kamu istirahat sejenak dan menyegarkan pikiran. 

Jika nanti kamu sudah siap untuk kembali belajar atau ada materi dari *Study Jam* yang ingin kamu diskusikan, beri tahu aku ya. Sekali lagi, kerja bagus dan semoga hasilnya memuaskan! 😊

Kamu: what i just finished?


### Gemini

Kamu baru saja menyelesaikan **ujian akhir** (*final exam*) kamu! 🎉 

Sekarang waktunya kamu bersantai dan mengistirahatkan pikiran setelah semua kerja kerasmu. Jika nanti kamu sudah siap untuk mulai belajar lagi di *Study Jam*, beri tahu aku ya! 😊

Kamu: exit
Chat selesai.


# Part 4 — Structured Output

## 13. Kenapa perlu structured output?

Kalau output AI hanya teks bebas, aplikasi sulit mengambil bagian tertentu.

Contoh output bebas:

```text
Materi ini membahas neural network dan CNN...
```

Aplikasi sulit mengambil mana judul, mana ringkasan, mana quiz.

Dengan JSON, output bisa seperti ini:

```json
{
  "title": "...",
  "summary": "...",
  "key_points": ["..."],
  "quiz": [...]
}
```

Ini lebih mudah diproses oleh program.

## 14. Buat schema output

Schema adalah cetakan output.

Kita akan meminta Gemini mengisi output dengan format:

- `title`
- `summary`
- `key_points`
- `quiz`
- `difficulty`
- `recommendation`

In [ ]:
class QuizItem(BaseModel):
    question: str = Field(description="Pertanyaan quiz untuk menguji pemahaman peserta.")
    answer: str = Field(description="Jawaban singkat dari pertanyaan quiz.")

class StudyAssistantOutput(BaseModel):
    title: str = Field(description="Judul singkat dari materi.")
    summary: str = Field(description="Ringkasan materi dalam bahasa Indonesia.")
    key_points: List[str] = Field(description="Daftar poin penting dari materi.")
    quiz: List[QuizItem] = Field(description="Daftar quiz singkat beserta jawabannya.")
    difficulty: Literal["beginner", "intermediate", "advanced"] = Field(
        description="Tingkat kesulitan materi."
    )
    recommendation: str = Field(description="Saran belajar lanjutan untuk peserta.")

## 15. Function AI Study Assistant

Function ini akan:

1. menerima materi teks,
2. mengirim prompt ke Gemini,
3. meminta output JSON sesuai schema,
4. memvalidasi JSON dengan Pydantic,
5. mengembalikan object Python.

In [ ]:
def generate_study_assistant(material_text):
    prompt = f'''
Kamu adalah AI Study Assistant untuk peserta study jam AI.

Tugas:
Analisis materi berikut dan ubah menjadi bahan belajar yang ringkas, jelas, dan mudah dipahami.

Materi:
"""
{material_text}
"""

Instruksi:
- Gunakan bahasa Indonesia
- Buat ringkasan yang manusiawi
- Ambil poin penting
- Buat 3 quiz singkat
- Jangan membuat informasi yang tidak ada hubungannya dengan materi
- Output harus sesuai schema yang diberikan
'''

    response = client.models.generate_content(
        model=MODEL_NAME,
        contents=prompt,
        config={
            "temperature": 0.2,
            "response_mime_type": "application/json",
            "response_schema": StudyAssistantOutput,
        }
    )

    try:
        result = StudyAssistantOutput.model_validate_json(response.text)
        return result
    except ValidationError as e:
        print("Output tidak sesuai schema.")
        print("Raw response:")
        print(response.text)
        raise e

## 16. Coba dengan materi contoh

In [ ]:
sample_material = '''
Neural network adalah model machine learning yang terinspirasi dari cara kerja otak manusia.
Model ini terdiri dari neuron-neuron buatan yang tersusun dalam layer.
Setiap neuron menerima input, mengalikannya dengan bobot, menambahkan bias, lalu melewati fungsi aktivasi.
Deep learning adalah neural network yang memiliki banyak hidden layer.
CNN adalah salah satu jenis neural network yang banyak digunakan untuk pengolahan gambar.
CNN bekerja dengan convolution layer untuk mengekstraksi fitur visual seperti garis, sudut, tekstur, dan pola.
'''

study_result = generate_study_assistant(sample_material)
study_result

StudyAssistantOutput(title='Pengenalan Neural Network dan CNN', summary='Neural network adalah model machine learning yang terinspirasi dari otak manusia, terdiri dari neuron buatan yang tersusun dalam layer. Setiap neuron memproses input menggunakan bobot, bias, dan fungsi aktivasi. Deep learning merupakan neural network dengan banyak hidden layer, sedangkan CNN adalah jenis neural network yang dirancang khusus untuk pengolahan gambar menggunakan convolution layer untuk mengekstrak fitur visual.', key_points=['Neural network terinspirasi dari cara kerja otak manusia dan terdiri dari neuron buatan dalam layer.', 'Proses dalam neuron melibatkan perkalian input dengan bobot, penambahan bias, dan fungsi aktivasi.', 'Deep learning adalah sebutan untuk neural network yang memiliki banyak hidden layer.', 'CNN (Convolutional Neural Network) digunakan untuk pengolahan gambar dengan mengekstrak fitur visual melalui convolution layer.'], quiz=[QuizItem(question='Apa yang menginspirasi pembuatan 

## 17. Tampilkan hasil dengan rapi

Output `study_result` sebenarnya sudah berhasil, tetapi tampilannya masih berupa object Python.

Sekarang kita ubah menjadi tampilan Markdown yang lebih enak dibaca.

In [ ]:
def show_study_result(result):
    key_points_md = "\n".join([f"- {point}" for point in result.key_points])

    quiz_md = ""
    for i, item in enumerate(result.quiz, start=1):
        quiz_md += f'''
**{i}. {item.question}**

Jawaban: {item.answer}

'''

    md = f'''
# {result.title}

## Ringkasan
{result.summary}

## Poin Penting
{key_points_md}

## Quiz
{quiz_md}

## Tingkat Kesulitan
`{result.difficulty}`

## Rekomendasi Belajar
{result.recommendation}
'''

    display(Markdown(md))

In [ ]:
show_study_result(study_result)


# Pengenalan Neural Network dan CNN

## Ringkasan
Neural network adalah model machine learning yang terinspirasi dari otak manusia, terdiri dari neuron buatan yang tersusun dalam layer. Setiap neuron memproses input menggunakan bobot, bias, dan fungsi aktivasi. Deep learning merupakan neural network dengan banyak hidden layer, sedangkan CNN adalah jenis neural network yang dirancang khusus untuk pengolahan gambar menggunakan convolution layer untuk mengekstrak fitur visual.

## Poin Penting
- Neural network terinspirasi dari cara kerja otak manusia dan terdiri dari neuron buatan dalam layer.
- Proses dalam neuron melibatkan perkalian input dengan bobot, penambahan bias, dan fungsi aktivasi.
- Deep learning adalah sebutan untuk neural network yang memiliki banyak hidden layer.
- CNN (Convolutional Neural Network) digunakan untuk pengolahan gambar dengan mengekstrak fitur visual melalui convolution layer.

## Quiz

**1. Apa yang menginspirasi pembuatan model neural network?**

Jawaban: Cara kerja otak manusia.


**2. Apakah perbedaan utama antara neural network biasa dengan deep learning?**

Jawaban: Deep learning memiliki banyak hidden layer.


**3. Layer apa yang digunakan pada CNN untuk mengekstrak fitur visual seperti garis dan tekstur?**

Jawaban: Convolution layer.



## Tingkat Kesulitan
`beginner`

## Rekomendasi Belajar
Pelajari lebih lanjut mengenai jenis-jenis fungsi aktivasi dan cobalah membangun model CNN sederhana menggunakan TensorFlow atau PyTorch untuk klasifikasi gambar.


# Part 5 — Mini UI in Colab

## 18. Prototype UI dengan ipywidgets

Kita akan membuat UI sederhana dengan:

- textarea untuk input materi
- button untuk generate
- output area untuk hasil

Ini belum deployment. Tapi flow-nya sudah mirip aplikasi:

**input user → API call → output rapi**

In [ ]:
import ipywidgets as widgets
from IPython.display import clear_output

In [ ]:
material_input = widgets.Textarea(
    value="",
    placeholder="Tempel materi belajar di sini...",
    description="Materi:",
    layout=widgets.Layout(width="100%", height="180px")
)

generate_button = widgets.Button(
    description="Generate Study Assistant",
    button_style="primary"
)

output_area = widgets.Output()

def on_generate_clicked(button):
    with output_area:
        clear_output()

        if not material_input.value.strip():
            print("Materi masih kosong. Isi dulu ya.")
            return

        print("Memproses materi...")

        try:
            result = generate_study_assistant(material_input.value)
            clear_output()
            show_study_result(result)
        except Exception as e:
            clear_output()
            print("Terjadi error saat memproses materi.")
            print("Detail error:")
            print(e)

generate_button.on_click(on_generate_clicked)

display(material_input, generate_button, output_area)

Textarea(value='', description='Materi:', layout=Layout(height='180px', width='100%'), placeholder='Tempel mat…

Button(button_style='primary', description='Generate Study Assistant', style=ButtonStyle())

Output()

# Part 6 — Multimodal Input: Image Analyzer

## 19. Konsep multimodal input

Multimodal berarti model bisa bekerja dengan lebih dari satu jenis data.

Contoh modality:

- text
- image
- audio
- video

Di bagian ini, kita akan mengirim gambar + prompt ke Gemini.

## 20. Schema Image Analyzer

In [ ]:
class ImageAnalysisOutput(BaseModel):
    description: str = Field(description="Deskripsi singkat isi gambar.")
    objects_detected: List[str] = Field(description="Objek utama yang terlihat dalam gambar.")
    caption: str = Field(description="Caption singkat yang cocok untuk gambar.")
    tags: List[str] = Field(description="Tag atau keyword relevan.")
    safety_note: str = Field(description="Catatan keamanan atau sensitivitas jika ada.")

## 21. Upload gambar

Jalankan cell ini, lalu upload satu gambar dari komputer kamu.

Contoh file yang cocok:

- poster event
- screenshot aplikasi
- foto produk
- diagram sederhana

In [ ]:
from google.colab import files

uploaded = files.upload()

image_path = list(uploaded.keys())[0]
print("File uploaded:", image_path)

Saving image.png to image.png
File uploaded: image.png


## 22. Function analyze image

In [ ]:
def analyze_image(image_path):
    uploaded_file = client.files.upload(file=image_path)

    prompt = '''
Kamu adalah AI visual analyzer.

Tugas:
Analisis gambar yang diberikan.

Instruksi:
- Jelaskan isi gambar secara singkat
- Deteksi objek utama
- Buat caption yang natural
- Buat tags relevan
- Tambahkan safety note jika gambar mengandung hal sensitif
- Gunakan bahasa Indonesia
'''

    response = client.models.generate_content(
        model=MODEL_NAME,
        contents=[uploaded_file, prompt],
        config={
            "temperature": 0.2,
            "response_mime_type": "application/json",
            "response_schema": ImageAnalysisOutput,
        }
    )

    try:
        return ImageAnalysisOutput.model_validate_json(response.text)
    except ValidationError as e:
        print("Gagal parse output image.")
        print("Raw response:")
        print(response.text)
        raise e

## 23. Tampilkan hasil image analyzer

In [ ]:
def show_image_result(result):
    objects_md = "\n".join([f"- {obj}" for obj in result.objects_detected])
    tags_text = ", ".join(result.tags)

    md = f'''
# Visual Caption & Analyzer

## Description
{result.description}

## Objects Detected
{objects_md}

## Caption
{result.caption}

## Tags
{tags_text}

## Safety Note
{result.safety_note}
'''
    display(Markdown(md))

In [ ]:
image_result = analyze_image(image_path)
show_image_result(image_result)


# Visual Caption & Analyzer

## Description
Tangkapan layar dari aplikasi Spotify versi desktop yang menampilkan lirik lagu 'MAYBE.' oleh Sienna Spiro. Di sebelah kanan terdapat panel informasi lagu dengan foto artis, judul lagu, dan rekomendasi video musik terkait.

## Objects Detected
- Tampilan aplikasi Spotify
- Lirik lagu
- Foto Sienna Spiro
- Kontrol pemutar musik

## Caption
Tampilan lirik lagu 'MAYBE.' oleh Sienna Spiro di aplikasi Spotify desktop.

## Tags
Spotify, Lirik Lagu, Sienna Spiro, Musik, Aplikasi Desktop, Pemutar Musik

## Safety Note
Aman. Gambar hanya berisi tangkapan layar aplikasi pemutar musik dengan lirik lagu.


# Part 7 — Multimodal Input: Audio Analyzer

## 24. Konsep audio input

Gemini juga bisa menerima audio sebagai input.

Use case:

- ringkasan rekaman kuliah
- transkrip meeting
- analisis voice note
- audio study assistant

> Untuk demo, pakai audio pendek agar prosesnya cepat.

## 25. Schema Audio Analyzer

In [ ]:
class AudioAnalysisOutput(BaseModel):
    transcript: str = Field(description="Transkrip atau isi utama audio dalam bahasa Indonesia.")
    summary: str = Field(description="Ringkasan singkat isi audio.")
    key_points: List[str] = Field(description="Poin-poin penting dari audio.")
    audio_type: str = Field(description="Jenis audio, misalnya percakapan, penjelasan materi, pengumuman, atau musik.")
    recommendation: str = Field(description="Saran tindak lanjut berdasarkan isi audio.")

## 26. Upload audio

Upload file audio pendek.

Format yang biasanya aman:

- `.mp3`
- `.wav`
- `.m4a`
- `.ogg`

In [ ]:
from google.colab import files

uploaded = files.upload()

audio_path = list(uploaded.keys())[0]
print("File uploaded:", audio_path)

Saving sound.mp3 to sound.mp3
File uploaded: sound.mp3


## 27. Function analyze audio

In [ ]:
def analyze_audio(audio_path):
    uploaded_file = client.files.upload(file=audio_path)

    prompt = '''
Kamu adalah AI audio analyzer.

Tugas:
Analisis audio yang diberikan.

Instruksi:
- Jika audio berisi ucapan, buat transkrip atau ringkasan isi ucapan
- Buat ringkasan singkat
- Ambil poin-poin penting
- Tentukan jenis audio
- Berikan rekomendasi tindak lanjut
- Gunakan bahasa Indonesia
'''

    response = client.models.generate_content(
        model=MODEL_NAME,
        contents=[uploaded_file, prompt],
        config={
            "temperature": 0.2,
            "response_mime_type": "application/json",
            "response_schema": AudioAnalysisOutput,
        }
    )

    try:
        return AudioAnalysisOutput.model_validate_json(response.text)
    except ValidationError as e:
        print("Gagal parse output audio.")
        print("Raw response:")
        print(response.text)
        raise e

## 28. Tampilkan hasil audio analyzer

In [ ]:
def show_audio_result(result):
    key_points_md = "\n".join([f"- {point}" for point in result.key_points])

    md = f'''
# Audio Transcript & Summary

## Audio Type
{result.audio_type}

## Transcript / Main Content
{result.transcript}

## Summary
{result.summary}

## Key Points
{key_points_md}

## Recommendation
{result.recommendation}
'''

    display(Markdown(md))

In [ ]:
audio_result = analyze_audio(audio_path)
show_audio_result(audio_result)


# Audio Transcript & Summary

## Audio Type
Penjelasan materi

## Transcript / Main Content
Halo semuanya. Selamat datang di Study Jam 5. Hari ini kita akan belajar membuat aplikasi AI sederhana menggunakan Gemini API. Kita akan mencoba prompting, struktur output, multimodal input, dan text to speech.

## Summary
Pembukaan sesi Study Jam 5 yang mengumumkan pembelajaran pembuatan aplikasi AI sederhana menggunakan Gemini API.

## Key Points
- Sesi pembelajaran Study Jam 5 tentang pembuatan aplikasi AI sederhana.
- Menggunakan Gemini API.
- Topik yang akan dipelajari meliputi prompting, struktur output, multimodal input, dan text to speech.

## Recommendation
Persiapkan lingkungan pengembangan (development environment) dan kunci API Gemini untuk mengikuti praktik pembuatan aplikasi AI sederhana ini.


# Part 8 — Multimodal Output: Text to Audio

## 29. Konsep Text-to-Speech

Sampai sini, multimodal kita dominan di input:

```text
Text/Image/Audio input → Text/JSON output
```

Sekarang kita coba output audio:

```text
Text → Gemini TTS → Audio
```

Catatan penting:

**TTS bukan chatbot.**

TTS hanya membacakan teks menjadi suara.

Kalau ingin AI menjawab lalu berbicara, pipeline-nya dua tahap:

```text
Prompt → Gemini text model → Text answer → Gemini TTS model → Audio answer
```

## 30. Function menyimpan WAV

Gemini TTS mengembalikan data audio mentah. Kita simpan sebagai file `.wav`.

In [ ]:
def save_wave_file(filename, pcm_data, channels=1, rate=24000, sample_width=2):
    with wave.open(filename, "wb") as wf:
        wf.setnchannels(channels)
        wf.setsampwidth(sample_width)
        wf.setframerate(rate)
        wf.writeframes(pcm_data)

## 31. Function Text-to-Speech

Function ini tugasnya:

```text
teks → audio
```

Bukan:

```text
prompt → AI berpikir → jawaban audio
```

Kalau ingin AI menjawab dulu, gunakan `ask_gemini()` dulu, lalu hasil jawabannya dikirim ke `text_to_speech()`.

In [ ]:
TTS_MODEL_CANDIDATES = [
    "gemini-2.5-flash-preview-tts",
    "gemini-2.5-pro-preview-tts",
    "gemini-3.1-flash-tts-preview",
]

def text_to_speech(text, output_filename="output.wav", voice_name="Kore"):
    last_error = None

    for tts_model in TTS_MODEL_CANDIDATES:
        try:
            response = client.models.generate_content(
                model=tts_model,
                contents=text,
                config=types.GenerateContentConfig(
                    response_modalities=["AUDIO"],
                    speech_config=types.SpeechConfig(
                        voice_config=types.VoiceConfig(
                            prebuilt_voice_config=types.PrebuiltVoiceConfig(
                                voice_name=voice_name
                            )
                        )
                    )
                )
            )

            audio_data = response.candidates[0].content.parts[0].inline_data.data

            save_wave_file(output_filename, audio_data)

            print("TTS berhasil dengan model:", tts_model)
            return output_filename

        except Exception as e:
            last_error = e
            print("Gagal dengan model:", tts_model)

    raise RuntimeError(f"Semua model TTS gagal. Error terakhir: {last_error}")

## 32. Coba TTS sederhana

Cell ini hanya membacakan teks yang kita berikan.

In [ ]:
audio_file = text_to_speech(
    text="Halo, selamat datang di Study Jam 5. Hari ini kita belajar membuat aplikasi AI dengan Gemini API.",
    output_filename="intro_study_jam.wav",
    voice_name="Kore"
)

display(Audio(audio_file))

TTS berhasil dengan model: gemini-2.5-flash-preview-tts


## 33. AI menjawab + audio

Sekarang kita buat flow dua tahap:

1. Gemini text model membuat jawaban
2. Gemini TTS membacakan jawaban

In [ ]:
def ask_gemini_with_audio(prompt, output_filename="answer.wav"):
    text_answer = ask_gemini(prompt)

    audio_file = text_to_speech(
        text_answer,
        output_filename=output_filename
    )

    display(Markdown("## Jawaban Teks"))
    display(Markdown(text_answer))

    display(Markdown("## Jawaban Audio"))
    display(Audio(audio_file))

    return text_answer, audio_file

In [ ]:
text_answer, audio_file = ask_gemini_with_audio(
    "Jelaskan apa itu API untuk mahasiswa pemula dalam bahasa Indonesia.",
    output_filename="jawaban_api.wav"
)

TTS berhasil dengan model: gemini-2.5-flash-preview-tts


## Jawaban Teks

Halo! Selamat datang di dunia teknologi. Sebagai mahasiswa pemula, memahami API adalah salah satu langkah awal yang sangat penting karena API adalah "lem" yang menyatukan internet modern saat ini.

Mari kita bahas API dengan cara yang paling sederhana dan mudah dipahami.

---

### Apa itu API?

**API** adalah singkatan dari **Application Programming Interface** (Antarmuka Pemrograman Aplikasi). 

Secara sederhana, **API adalah "jembatan" atau "penerjemah" yang memungkinkan dua aplikasi atau sistem yang berbeda untuk saling berkomunikasi dan bertukar data.**

---

### Analogi Paling Mudah: "Restoran"

Bayangkan kamu sedang makan di sebuah restoran:

1. **Kamu (Pelanggan)** adalah **Aplikasi/User** yang ingin meminta sesuatu.
2. **Dapur Restoran** adalah **Server/Database** tempat makanan (data) dibuat dan disimpan. Kamu tidak boleh masuk langsung ke dapur karena berbahaya dan berantakan.
3. **Pelayan** adalah **API**.

**Prosesnya:**
Kamu melihat menu, lalu memesan makanan lewat **Pelayan (API)**. Pelayan pergi ke **Dapur (Server)** untuk menyampaikan pesananmu. Setelah makanan siap, pelayan membawanya kembali dan menyajikannya di mejamu. 

Tanpa pelayan (API), kamu tidak bisa memesan makanan dari dapur dengan aman dan teratur.

---

### Contoh Nyata API dalam Kehidupan Sehari-hari

Kamu pasti sering menggunakan API tanpa kamu sadari. Ini beberapa contohnya:

1. **Login dengan Google / Facebook**
   Saat kamu ingin mendaftar di aplikasi baru (misalnya Spotify atau Canva), sering kali ada tombol *"Login with Google"*. Aplikasi tersebut menggunakan **API Google** untuk memverifikasi identitasmu tanpa perlu tahu password Google-mu.
2. **Peta di Aplikasi Gojek / Grab**
   Gojek tidak membuat peta dunia sendiri dari nol. Mereka menggunakan **API Google Maps** untuk menampilkan peta dan melacak driver di aplikasi mereka.
3. **Cek Ongkir di E-commerce**
   Saat kamu belanja di Shopee atau Tokopedia, sistem bisa langsung tahu biaya kirim JNE atau J&T. E-commerce tersebut menggunakan **API dari pihak ekspedisi** untuk mengambil data tarif secara *real-time*.

---

### Mengapa API Sangat Penting bagi Developer?

Sebagai calon developer atau praktisi IT, API akan sangat membantu hidupmu karena:

* **Menghemat Waktu (Tidak Perlu Membuat dari Nol):** Kamu tidak perlu membuat sistem pembayaran sendiri, cukup gunakan API Midtrans atau Stripe. Kamu tidak perlu membuat sistem SMS OTP sendiri, cukup pakai API Twilio.
* **Keamanan:** API membatasi akses. Pihak luar hanya bisa mengakses data yang diizinkan oleh API, sehingga database utama tetap aman di belakang layar.
* **Fleksibilitas:** Aplikasi Android, iOS, dan Website bisa menggunakan satu API yang sama untuk mengambil data dari database yang sama.

---

### Bagaimana Cara Kerja API secara Teknis (Sederhana)?

API biasanya bekerja dengan format **Request (Permintaan)** dan **Response (Tanggapan)**:

1. **Request:** Aplikasi kamu mengirim permintaan ke API (Contoh: *"Tolong berikan data cuaca Jakarta hari ini"*).
2. **Response:** API merespons dengan memberikan data tersebut, biasanya dalam format teks ringan yang disebut **JSON** (JavaScript Object Notation).

Contoh data JSON yang dikembalikan API cuaca:
```json
{
  "kota": "Jakarta",
  "suhu": "31 C",
  "kondisi": "Cerah Berawan"
}
```
Data JSON inilah yang kemudian diolah oleh aplikasimu agar tampil cantik di layar HP pengguna.

---

### Kesimpulan

API adalah cara komputer berbicara dengan komputer lain secara aman dan efisien. Sebagai mahasiswa, nanti kamu akan sering mendengar istilah seperti **REST API**, **API Key**, atau **Endpoint**. Jangan bingung, prinsip dasarnya tetap sama: **mereka semua adalah pelayan yang menghubungkan aplikasimu dengan data yang kamu butuhkan.**

Semangat belajarnya! Jika ada istilah yang masih membingungkan, silakan tanyakan lagi.

## Jawaban Audio

## 34. Study Assistant + Audio Summary

Sekarang kita gabungkan structured output dan TTS.

Flow:

```text
Materi → Study Assistant JSON → ambil summary → TTS → audio summary
```

In [ ]:
def generate_study_assistant_with_audio(material_text, output_filename="study_summary.wav"):
    result = generate_study_assistant(material_text)

    show_study_result(result)

    audio_prompt = f'''
Say in a calm, friendly, and clear Indonesian mentor voice:

Berikut ringkasan materi:
{result.summary}

Rekomendasi belajar:
{result.recommendation}
'''

    audio_file = text_to_speech(
        text=audio_prompt,
        output_filename=output_filename,
        voice_name="Kore"
    )

    display(Markdown("## Audio Summary"))
    display(Audio(audio_file))

    return result, audio_file

In [ ]:
result_with_audio, summary_audio = generate_study_assistant_with_audio(sample_material)


# Pengenalan Neural Network dan CNN

## Ringkasan
Neural network adalah model machine learning yang terinspirasi dari cara kerja otak manusia dengan menggunakan neuron buatan yang tersusun dalam layer. Deep learning merupakan neural network dengan banyak hidden layer, sedangkan CNN adalah variasi khusus yang sangat efektif untuk pengolahan gambar dengan mengekstrak fitur visual melalui convolution layer.

## Poin Penting
- Neural network terinspirasi dari otak manusia dan terdiri dari neuron buatan dalam beberapa layer.
- Setiap neuron memproses input dengan mengalikannya dengan bobot, menambah bias, dan meneruskannya ke fungsi aktivasi.
- Deep learning adalah neural network yang memiliki banyak hidden layer.
- CNN (Convolutional Neural Network) menggunakan convolution layer untuk mengekstrak fitur visual seperti garis, sudut, dan tekstur pada gambar.

## Quiz

**1. Apa yang menginspirasi struktur dari neural network?**

Jawaban: Cara kerja otak manusia.


**2. Bagaimana proses komputasi dasar di dalam sebuah neuron buatan?**

Jawaban: Menerima input, mengalikannya dengan bobot, menambahkan bias, lalu melewati fungsi aktivasi.


**3. Layer apa yang digunakan CNN untuk mengekstrak fitur visual dari gambar?**

Jawaban: Convolution layer.



## Tingkat Kesulitan
`beginner`

## Rekomendasi Belajar
Pelajari lebih lanjut tentang jenis-jenis fungsi aktivasi dan cobalah mempraktikkan pembuatan model CNN sederhana menggunakan library seperti TensorFlow atau PyTorch.


TTS berhasil dengan model: gemini-2.5-flash-preview-tts


## Audio Summary

# Part 9 — Common Errors and Debugging

## 35. Debugging checklist

Kalau error, cek ini dulu:

### API key tidak terbaca

Pastikan secret di Colab bernama persis:

```text
GEMINI_API_KEY
```

### Package conflict

Jangan install dengan:

```python
!pip install -U google-genai pydantic pillow ipywidgets
```

Pakai:

```python
!pip install -q "google-genai>=1.66.0,<2.0.0"
```

### Rate limit / quota

Kalau muncul error seperti `429`, `RESOURCE_EXHAUSTED`, atau quota exceeded:

- tunggu beberapa saat,
- kurangi jumlah request,
- pakai input lebih pendek,
- cek limit aktif di AI Studio.

### JSON tidak valid

Cek raw response:

```python
print(response.text)
```

### File gagal diproses

Cek:

- format file,
- ukuran file,
- durasi audio,
- apakah file benar-benar terupload.

# Penutup

Selamat! 🎉

Kamu sudah mencoba flow dasar aplikasi AI modern:

```text
User input → Gemini API → response → parsing → output UI
```

Dan kamu juga sudah melihat bahwa AI app bisa memakai beberapa model sekaligus:

```text
Text model → menghasilkan jawaban
TTS model → membacakan jawaban
```

Ini adalah pondasi awal untuk menjadi **AI product builder**.